# RAFT au lieu des démons — strain des réplicats GRAZIANA OD

Les démons (FastSymmetricForces, σ = 15) donnent sur les one-cycles cascade_v9 de MODICA GRAZIANA OD
un strain rétinien **non répétable** : ICC(1,1) = 0,04 sur le profil des 5 bandes, contre 0,61 pour le
témoin dCT. On remplace ici le recalage par le flot optique **RAFT** (Teed & Deng, 2020,
[arXiv 2003.12039](https://arxiv.org/abs/2003.12039)) : corrélation dense entre toutes les paires de
pixels, puis raffinement récurrent du flot. Le reste de la chaîne ne change pas :

1. les one-cycles de `one_cycle_6beats_6bins/cycles/<slug>.npz` (6 battements × 6 bins) sont relus
   **tels quels** par le `prepare` de `Reproducibility/compute_one_cycle_strain.py`. Celui-ci égalise
   par A-scan, choisit le bin de référence (choroïde la plus mince), segmente la rétine par Otsu,
   applique le crop et découpe les 5 bandes latérales ;
2. **RAFT** (`torchvision`, poids `C_T_SKHT_V2`) mesure le déplacement du bin mince vers chaque
   bin mobile, avec la convention ITK : `warped(x) = moving(x + u(x))` ;
3. le strain est `e_yy = ∂u_y/∂y` (`cds.strain_yy`, aucun lissage ajouté). Le marqueur est la paire
   bin mince → bin épais.

Deux comparatifs de répétabilité, chaque fois RAFT contre démons :

- **(1)** ICC du strain rétinien moyen **par colonne**, c'est-à-dire par bande latérale comme dans
  la chaîne démons. Une variante prend chaque A-scan comme sujet ;
- **(2)** ICC **pixel à pixel** : les réplicats sont mis en correspondance dans le repère d'OD1
  (translation, puis RAFT entre leurs références), et les cartes sont comparées point par point.

In [1]:
from __future__ import annotations

import json
import sys
import time
from datetime import datetime
from pathlib import Path

import numpy as np
import pandas as pd
import plotly.graph_objects as go
import plotly.io as pio
import torch
import torch.nn.functional as F
from IPython.display import Markdown, display
from plotly.subplots import make_subplots
from scipy import ndimage
from torchvision.models.optical_flow import Raft_Large_Weights, raft_large

# CUDA est initialise AVANT d'importer la chaine demons : ``compute_demons_strain`` pose
# CUDA_VISIBLE_DEVICES="" a son import (le lot tourne sur CPU), ce qui priverait RAFT du GPU.
DEVICE = "cuda" if torch.cuda.is_available() else "cpu"
torch.zeros(1, device=DEVICE)

REPO = Path.cwd().resolve()
if REPO.name == "notebook":
    REPO = REPO.parent
for p in (REPO / "src", REPO / "Astronauts", REPO / "Reproducibility"):
    if str(p) not in sys.path:
        sys.path.insert(0, str(p))

import compute_one_cycle_strain as ocs  # noqa: E402  (importe cds, fixe REF_CASES/SIGMAS)

cds = ocs.cds
pio.templates.default = "plotly_white"
print(f"depot : {REPO} | RAFT sur {DEVICE} ({torch.cuda.get_device_name(0) if DEVICE == 'cuda' else 'cpu'})")

C:\Users\transformer\anaconda3\envs\pyOR\Lib\site-packages\tqdm\auto.py:21: TqdmWarning: IProgress not found. Please update jupyter and ipywidgets. See https://ipywidgets.readthedocs.io/en/stable/user_install.html
  from .autonotebook import tqdm as notebook_tqdm


W0918 11:04:58.703000 24352 site-packages\torch\utils\flop_counter.py:29] triton not found; flop counting will not work for triton kernels


depot : C:\Users\transformer\Documents\Nicolas\mes-codes\SANSORI\OcularRigidity | RAFT sur cuda (NVIDIA GeForce RTX 3060)


In [2]:
# --------------------------------------------------------------------------- #
# Parametres
# --------------------------------------------------------------------------- #
SLUGS = ocs.DEFAULT_SLUGS
ONE_CYCLE_DIR = ocs.ONE_CYCLE_DIR
DEMONS_DIR = ocs.OUT_DIR                      # demons_strain_s15 : champs et ICC de reference
OUT_DIR = ONE_CYCLE_DIR / "raft_strain"
N_BINS, N_COLUMNS = cds.N_BINS, cds.N_COLUMNS

UPSCALE = 2          # RAFT tourne sur l'image agrandie (cf. test synthetique ci-dessous)
RAFT_ITERS = 32      # raffinements recurrents du flot
BLOC = 8             # cote des blocs (px) pour l'ICC par blocs et le bootstrap
N_BOOT = 1000
SEUIL_DICE = 0.9     # correspondance inter-replicats jugee inutilisable en dessous

C_REPLICAT = {1: "#3987e5", 2: "#eb6834", 3: "#1baf7a"}
C_METHODE = {"démons": "#8a8a8a", "RAFT": "#7b3fbf"}
DS_Y, DS_X = 2, 3    # sous-echantillonnage des cartes affichees
RNG = np.random.default_rng(0)


def fr(x, chiffres=1):
    if x is None or (isinstance(x, float) and not np.isfinite(x)):
        return "—"
    return f"{{:.{chiffres}f}}".format(x).replace(".", ",")

## 1. RAFT

On normalise les deux images **ensemble** dans [-1, 1], avec les percentiles 0,5–99,5 de la paire.
On les recopie ensuite sur 3 canaux, on les agrandit d'un facteur `UPSCALE` (bicubique) et on les
complète au multiple de 8. Le flot est ramené à la taille native, puis divisé par le facteur.

`raft(fixed, moving)` garde la convention ITK des démons : image1 = fixe, image2 = mobile, donc
`fixed(x) ≈ moving(x + u(x))`. Un `e_yy > 0` signifie un tissu plus épais dans le mobile. Le
jacobien est `det(I + ∇u)`.

In [3]:
_MODELE = None


def modele():
    global _MODELE
    if _MODELE is None:
        _MODELE = raft_large(weights=Raft_Large_Weights.C_T_SKHT_V2, progress=False).eval().to(DEVICE)
    return _MODELE


def warp(img, u):
    # warped(x) = img(x + u(x)) ; u (h, w, 2) = (u_x, u_y) ; bilineaire, 0 hors champ.
    h, w = img.shape
    yy, xx = np.mgrid[0:h, 0:w].astype(np.float32)
    grid = np.stack([(xx + u[..., 0]) / (w - 1) * 2 - 1, (yy + u[..., 1]) / (h - 1) * 2 - 1], -1)
    t = torch.as_tensor(np.ascontiguousarray(img, np.float32))[None, None]
    g = torch.as_tensor(grid.astype(np.float32))[None]
    return F.grid_sample(t, g, mode="bilinear", padding_mode="zeros", align_corners=True)[0, 0].numpy()


def warp_nan(carte, u):
    # Idem pour une carte portant des NaN : valeur et validite sont warpees separement.
    ok = np.isfinite(carte)
    val = warp(np.where(ok, carte, 0.0), u)
    poids = warp(ok.astype(np.float32), u)
    return np.where(poids > 0.999, val / np.maximum(poids, 1e-6), np.nan)


@torch.inference_mode()
def raft_flow(fixed, moving, upscale=UPSCALE, iters=RAFT_ITERS):
    f, m = np.asarray(fixed, np.float32), np.asarray(moving, np.float32)
    lo, hi = np.percentile(np.concatenate([f.ravel(), m.ravel()]), [0.5, 99.5])

    def tenseur(a):
        a = (np.clip((a - lo) / max(hi - lo, 1e-6), 0, 1) * 2 - 1).astype(np.float32)
        t = torch.as_tensor(a)[None, None].to(DEVICE)
        if upscale != 1:
            t = F.interpolate(t, scale_factor=upscale, mode="bicubic", align_corners=False)
        return t.repeat(1, 3, 1, 1)

    a, b = tenseur(f), tenseur(m)
    H, W = a.shape[-2:]
    ph, pw = (-H) % 8, (-W) % 8
    a = F.pad(a, (0, pw, 0, ph), mode="replicate")
    b = F.pad(b, (0, pw, 0, ph), mode="replicate")
    flot = modele()(a, b, num_flow_updates=iters)[-1][:, :, :H, :W]
    if upscale != 1:
        flot = F.interpolate(flot, size=f.shape, mode="bilinear", align_corners=False) / upscale
    return flot[0].permute(1, 2, 0).cpu().numpy().astype(np.float64)


def jacobien(u):
    dux_dy, dux_dx = np.gradient(u[..., 0])
    duy_dy, duy_dx = np.gradient(u[..., 1])
    return (1 + dux_dx) * (1 + duy_dy) - dux_dy * duy_dx


def raft(fixed, moving, upscale=UPSCALE):
    # Meme dict que ``cds.run_demons`` (champ, image recalee, jacobien, temps).
    t0 = time.perf_counter()
    u = raft_flow(fixed, moving, upscale)
    if DEVICE == "cuda":
        torch.cuda.synchronize()
    return {"field": u, "warped": warp(moving, u), "jacobian": jacobien(u),
            "elapsed": time.perf_counter() - t0}

## 2. Préparation des réplicats

`ocs.prepare` relit les one-cycles, égalise par A-scan puis appelle `cds._prepare_regions`. C'est
exactement l'entrée donnée aux démons.

In [4]:
conds = pd.read_csv(ONE_CYCLE_DIR / "conditions.csv").set_index("slug")
PREPS = {}
for s in SLUGS:
    t0 = time.perf_counter()
    PREPS[s] = ocs.prepare(s, conds.loc[s, "n_beats"])
    p = PREPS[s]
    print(f"{s}: {p.n_groups} one-cycles, crop {p.crop}, bins minces {p.ref_bins.tolist()}, "
          f"um/px {p.um_y:.2f} x {p.um_x:.2f} ({time.perf_counter() - t0:.0f} s)")

MODICA_GRAZIANA_OD1: 5 one-cycles, crop (144, 354), bins minces [1, 0, 1, 1, 0], um/px 3.90 x 12.40 (3 s)


MODICA_GRAZIANA_OD2: 5 one-cycles, crop (97, 305), bins minces [4, 4, 3, 3, 4], um/px 3.90 x 12.50 (3 s)


MODICA_GRAZIANA_OD3: 5 one-cycles, crop (117, 321), bins minces [0, 1, 1, 1, 1], um/px 3.90 x 12.40 (3 s)


### Test synthétique : dilatation connue de ±2 % de la choroïde

Sur le bin mince du cycle 1 d'OD1, on impose à chaque colonne un champ `u_y` connu :
- nul au-dessus de la choroïde ;
- `e·(y − haut)` dans la choroïde, soit une dilatation de ±2 % ;
- constant en dessous.

On en déduit l'image mobile. RAFT doit retrouver `e_yy = e` dans la choroïde et 0 dans la rétine.

In [5]:
p = PREPS[SLUGS[0]]
fixe = p.cycles[int(p.ref_bins[0])].astype(np.float64)
h, w = fixe.shape
haut = p.roi.argmax(0).astype(float)
bas = h - 1 - p.roi[::-1].argmax(0).astype(float)
yy = np.arange(h)[:, None].astype(float)
lignes = []
for e in (0.02, -0.02):
    U = np.where(yy < haut, 0, np.where(yy <= bas, e * (yy - haut), e * (bas - haut))) * p.roi.any(0)
    mobile = np.empty_like(fixe)
    for x in range(w):  # mobile(y + U(y)) = fixe(y)
        mobile[:, x] = np.interp(np.arange(h), np.arange(h) + U[:, x], fixe[:, x])
    for up in (1, 2, 3):
        r = raft(fixe, mobile, upscale=up)
        s = cds.strain_yy(r["field"])
        lignes.append({"e imposé": e, "UPSCALE": up,
                       "e_yy choroïde (médiane)": np.median(s[p.roi]),
                       "e_yy rétine (médiane)": np.median(s[p.retina]),
                       "erreur u_y RMS (px)": np.sqrt(((r["field"][..., 1] - U)[p.tissue] ** 2).mean()),
                       "RMS avant": cds.rms(fixe, mobile, p.tissue),
                       "RMS après": cds.rms(fixe, r["warped"], p.tissue),
                       "temps (s)": r["elapsed"]})
SYNTH = pd.DataFrame(lignes)
display(SYNTH.round(4))

,e imposé,UPSCALE,e_yy choroïde (médiane),e_yy rétine (médiane),erreur u_y RMS (px),RMS avant,RMS après,temps (s)
0,0.02,1,0.0163,0.0005,0.0576,2.1904,0.9450,0.8142
1,0.02,2,0.0187,0.0005,0.0764,2.1904,0.7925,0.4908
2,0.02,3,0.0195,0.0002,0.0431,2.1904,0.7766,1.4061
3,-0.02,1,-0.0155,-0.0005,0.0710,2.2248,0.9566,0.1670
4,-0.02,2,-0.0186,-0.0003,0.0251,2.2248,0.8280,0.4572
5,-0.02,3,-0.0179,-0.0003,0.0292,2.2248,0.8034,1.0002


## 3. RAFT : bin mince → bins mobiles

La boucle est celle de `cds.run_condition_demons` (référence locale), avec `raft` au lieu de
`run_demons`. Elle produit les mêmes lignes `bins` et `regions`, et la même paire marqueur (bin
mince → bin épais).

Contrôle ajouté, `dCT_flot_um` : l'épaississement que le flot attribue à la choroïde, soit
`u_y(bas) − u_y(haut)` moyenné sur les colonnes exploitables. Il doit retrouver le dCT mesuré sur
les masques.

In [6]:
def dct_du_flot(u_y, roi, cols, um_y):
    haut = roi.argmax(0)
    bas = roi.shape[0] - 1 - roi[::-1].argmax(0)
    c = cols[roi[:, cols].any(0)]
    return float(np.mean(u_y[bas[c], c] - u_y[haut[c], c])) * um_y


def run_replicate_raft(slug, prep):
    m = ocs.RE_SLUG.match(slug)
    extra = {"replicate": int(m["replicate"]), "participant": m["participant"], "eye": m["eye"]}
    thick = np.full(prep.n_groups, -1, dtype=int)
    for g in range(prep.n_groups):
        if prep.ref_bins[g] >= 0 and np.isfinite(prep.th_grid[g]).sum() >= 2:
            thick[g] = int(np.nanargmax(prep.th_grid[g]))
    retina, roi, tissue, um_y, um_x = prep.retina, prep.roi, prep.tissue, prep.um_y, prep.um_x
    bin_rows, region_rows, fields = [], [], {}
    for g in range(prep.n_groups):
        ref = int(prep.ref_bins[g])
        if ref < 0 or prep.counts_mask[g * N_BINS + ref] == 0:
            continue
        ref_slot = g * N_BINS + ref
        fixed = prep.cycles[ref_slot]
        ct_ref = float(prep.th_grid[g, ref])
        for b in range(N_BINS):
            slot = g * N_BINS + b
            if b == ref or prep.counts_mask[slot] == 0:
                continue
            moving = prep.cycles[slot]
            if not (np.isfinite(moving).all() and np.isfinite(fixed).all()):
                continue
            res = raft(fixed, moving)
            u = res["field"]
            strain = cds.strain_yy(u).astype(np.float32)
            ct_um = float(prep.th_grid[g, b])
            est_epais = bool(b == thick[g])
            bin_rows.append({
                "slug": slug, "one_cycle": g + 1, "bin": b, "ref_bin": ref, **extra,
                "is_thick": est_epais, "n_frames_bin": int(prep.counts_mask[slot]),
                "CT_um": round(ct_um, 3), "dCT_um": round(ct_um - ct_ref, 3),
                "dCT_flot_um": round(dct_du_flot(u[..., 1], roi, prep.cols, um_y), 3),
                "rms_avant": round(cds.rms(fixed, moving, tissue), 3),
                "rms_apres": round(cds.rms(fixed, res["warped"], tissue), 3),
                "u_max_um": round(float(np.hypot(u[..., 0] * um_x, u[..., 1] * um_y).max()), 2),
                "jac_neg_pct": round(100 * float((res["jacobian"] <= 0).mean()), 4),
                "strain_retine_moy": round(float(np.mean(strain[retina])), 6),
                "strain_retine_med": round(float(np.median(strain[retina])), 6),
                "strain_retine_p95": round(cds.strain_p95_signe(strain[retina]), 6),
                "strain_choroide_med": round(float(np.median(strain[roi])), 6),
                "temps_s": round(res["elapsed"], 2),
            })
            for k in range(N_COLUMNS):
                bc = prep.band_cols[k]
                m_ret = retina & prep.column_masks[k]
                ct_reg = float(prep.mask_cycles[slot][:, bc].sum(axis=0).mean()) * um_y
                ct_reg_ref = float(prep.mask_cycles[ref_slot][:, bc].sum(axis=0).mean()) * um_y
                region_rows.append({
                    "slug": slug, "one_cycle": g + 1, "bin": b, **extra, "is_thick": est_epais,
                    "region": cds.column_label(k, prep.eye), "k": k,
                    "CT_um": round(ct_um, 3), "dCT_um": round(ct_um - ct_ref, 3),
                    "CT_region_um": round(ct_reg, 3), "dCT_region_um": round(ct_reg - ct_reg_ref, 3),
                    "strain_retine": float(np.mean(strain[m_ret])),
                    "strain_retine_med": float(np.median(strain[m_ret])),
                    "strain_retine_p95": cds.strain_p95_signe(strain[m_ret]),
                })
            if est_epais:
                fields[g] = {"u_x": u[..., 0].astype(np.float32), "u_y": u[..., 1].astype(np.float32),
                             "strain": strain, "jacobian": res["jacobian"].astype(np.float32),
                             "warped": res["warped"].astype(np.float32),
                             "fixed": np.asarray(fixed, np.float32)}
    return bin_rows, region_rows, fields, thick


def payload(slug, prep, fields, thick):
    # Meme format que ``demons_strain_s15/fields/<slug>.npz`` (plus u_x).
    out = {"slug": np.array(slug), "um_y": prep.um_y, "um_x": prep.um_x,
           "crop": np.asarray(prep.crop), "roi": prep.roi, "retina": prep.retina,
           "tissue": prep.tissue, "column_masks": np.stack(prep.column_masks),
           "column_labels": np.array([cds.column_label(k, prep.eye) for k in range(N_COLUMNS)]),
           "ref_bins": prep.ref_bins, "thick_bins": thick, "th_grid_um": prep.th_grid,
           "n_groups": prep.n_groups, "cols": prep.cols,
           "fixed_global": prep.fixed_global.astype(np.float32)}
    for g, f in fields.items():
        for cle, v in f.items():
            out[f"c{g}__{cle}"] = v
    return out


t0 = time.perf_counter()
all_bins, all_regions, FIELDS = [], [], {}
for s in SLUGS:
    b, r, f, thick = run_replicate_raft(s, PREPS[s])
    all_bins += b
    all_regions += r
    FIELDS[s] = payload(s, PREPS[s], f, thick)
    print(f"{s}: {len(b)} recalages, bins epais {thick.tolist()}")
BINS = pd.DataFrame(all_bins)
REGIONS = pd.DataFrame(all_regions)
MARK = REGIONS[REGIONS["is_thick"]].copy()
print(f"RAFT : {len(BINS)} recalages en {time.perf_counter() - t0:.0f} s")

# Champs demons de la meme paire marqueur, relus (aucun demon relance).
DEMONS = {s: dict(np.load(DEMONS_DIR / "fields" / f"{s}.npz")) for s in SLUGS}
DEMONS_BINS = pd.read_csv(DEMONS_DIR / "bins.csv")
for s in SLUGS:
    assert tuple(DEMONS[s]["crop"]) == tuple(PREPS[s].crop), "crop demons different"
    assert np.array_equal(DEMONS[s]["thick_bins"], FIELDS[s]["thick_bins"]), "paire marqueur differente"

MODICA_GRAZIANA_OD1: 25 recalages, bins epais [3, 3, 3, 2, 2]


MODICA_GRAZIANA_OD2: 25 recalages, bins epais [0, 5, 5, 5, 5]


MODICA_GRAZIANA_OD3: 25 recalages, bins epais [3, 4, 3, 3, 3]
RAFT : 75 recalages en 35 s


### Contrôles du recalage (paires marqueur)

RAFT et démons sur les mêmes paires : RMS avant et après, jacobien négatif, |u| max, strain
choroïdien médian, et dCT déduit du flot face au dCT des masques.

In [7]:
def dct_flot_demons(s, g):
    f = DEMONS[s]
    return dct_du_flot(f[f"c{g}__u_y"], f["roi"], PREPS[s].cols, float(f["um_y"]))


rows = []
for _, r in BINS[BINS["is_thick"]].iterrows():
    d = DEMONS_BINS[(DEMONS_BINS["slug"] == r.slug) & (DEMONS_BINS["one_cycle"] == r.one_cycle)
                    & (DEMONS_BINS["bin"] == r.bin)].iloc[0]
    rows.append({"slug": r.slug[-3:], "cycle": r.one_cycle, "bins": f"{r.ref_bin}→{r.bin}",
                 "dCT masques (µm)": r.dCT_um,
                 "dCT flot RAFT": r.dCT_flot_um, "dCT flot démons": dct_flot_demons(r.slug, r.one_cycle - 1),
                 "e_yy choroïde RAFT": r.strain_choroide_med, "e_yy choroïde démons": d.strain_choroide_med,
                 "RMS avant": r.rms_avant, "RMS après RAFT": r.rms_apres, "RMS après démons": d.rms_apres,
                 "|u|max RAFT (µm)": r.u_max_um, "|u|max démons (µm)": d.u_max_um,
                 "jac<0 RAFT %": r.jac_neg_pct, "jac<0 démons %": d.jac_neg_pct,
                 "e_yy rétine RAFT ×1e3": 1e3 * r.strain_retine_moy,
                 "e_yy rétine démons ×1e3": 1e3 * d.strain_retine_moy})
CONTROLE = pd.DataFrame(rows)
display(CONTROLE.round(3))
c = CONTROLE
display(Markdown(
    f"Sur les {len(c)} paires marqueur :\n\n"
    f"- **strain choroïdien médian > 0** dans **{(c['e_yy choroïde RAFT'] > 0).sum()}** cas avec RAFT, "
    f"contre {(c['e_yy choroïde démons'] > 0).sum()} avec les démons ;\n"
    f"- **r(dCT masques, dCT flot)** = **{fr(np.corrcoef(c['dCT masques (µm)'], c['dCT flot RAFT'])[0, 1], 2)}** "
    f"(RAFT) et {fr(np.corrcoef(c['dCT masques (µm)'], c['dCT flot démons'])[0, 1], 2)} (démons) ;\n"
    f"- **rapport médian dCT flot / dCT masques** : "
    f"{fr(np.median(c['dCT flot RAFT'] / c['dCT masques (µm)']), 2)} (RAFT), "
    f"{fr(np.median(c['dCT flot démons'] / c['dCT masques (µm)']), 2)} (démons) ;\n"
    f"- **RMS relatif après recalage** : {fr(100 * np.median(c['RMS après RAFT'] / c['RMS avant'] - 1), 0)} % (RAFT), "
    f"{fr(100 * np.median(c['RMS après démons'] / c['RMS avant'] - 1), 0)} % (démons)."))

,slug,cycle,bins,dCT masques (µm),dCT flot RAFT,dCT flot démons,e_yy choroïde RAFT,e_yy choroïde démons,RMS avant,RMS après RAFT,RMS après démons,|u|max RAFT (µm),|u|max démons (µm),jac<0 RAFT %,jac<0 démons %,e_yy rétine RAFT ×1e3,e_yy rétine démons ×1e3
0,OD1,1,1→3,5.786,0.120,1.083,0.000,0.005,6.677,6.382,6.060,3.52,19.06,0.0,0.0,0.213,-0.044
1,OD1,2,0→3,4.492,0.122,1.203,0.000,0.007,7.559,7.345,6.789,2.76,22.61,0.0,0.0,0.328,0.010
2,OD1,3,1→3,3.928,0.090,1.394,0.000,0.008,7.428,6.883,6.448,2.13,20.72,0.0,0.0,0.345,2.224
3,OD1,4,1→2,4.029,0.119,1.813,0.000,0.009,6.759,6.461,6.208,4.27,23.20,0.0,0.0,0.329,-1.062
4,OD1,5,0→2,3.206,0.057,1.637,0.000,0.008,5.680,5.355,5.109,3.19,13.46,0.0,0.0,0.056,-0.347
5,OD2,1,4→0,4.111,0.125,0.372,0.000,0.005,8.649,7.189,6.650,4.22,12.82,0.0,0.0,0.463,1.387
6,OD2,2,4→5,3.325,0.878,0.594,0.000,0.003,8.462,7.443,6.414,8.87,17.73,0.0,0.0,-2.057,0.079
7,OD2,3,3→5,4.755,0.108,1.116,0.000,0.007,8.930,8.333,7.308,4.11,14.50,0.0,0.0,-0.011,-0.248
8,OD2,4,3→5,3.981,0.205,0.913,0.000,0.006,9.992,8.966,6.764,6.09,12.30,0.0,0.0,0.337,0.828
9,OD2,5,4→5,4.397,0.086,1.887,0.000,0.009,6.559,6.070,5.260,2.08,21.90,0.0,0.0,0.190,1.446


Sur les 15 paires marqueur :

- **strain choroïdien médian > 0** dans **15** cas avec RAFT, contre 15 avec les démons ;
- **r(dCT masques, dCT flot)** = **-0,33** (RAFT) et 0,23 (démons) ;
- **rapport médian dCT flot / dCT masques** : 0,03 (RAFT), 0,35 (démons) ;
- **RMS relatif après recalage** : -6 % (RAFT), -11 % (démons).

## 4. Comparatif (1) : ICC sur la moyenne du strain par colonne

Protocole de la chaîne démons (`ocs.icc_table`) :
- **sujets** : les 5 bandes latérales ;
- **évaluateurs** : les 3 réplicats ;
- **valeur** : la médiane des one-cycles de la paire marqueur.

Les ICC démons sont relus dans `demons_strain_s15/icc.csv`. Le témoin dCT, tiré des masques, est
commun aux deux méthodes.

In [8]:
ICC_RAFT = ocs.icc_table(MARK).assign(methode="RAFT")
ICC_DEMONS = pd.read_csv(DEMONS_DIR / "icc.csv").assign(methode="démons")
ICC_BANDES = pd.concat([ICC_DEMONS, ICC_RAFT], ignore_index=True)

lignes = ["| marqueur | méthode | ICC(1,1) | ICC(A,1) | ICC(C,1) |", "|:--|:--|--:|--:|--:|"]
for (col, meth), d in ICC_BANDES.groupby(["marqueur", "methode"], sort=False):
    if col == "dCT_region_um" and meth == "démons":
        continue
    d = d.set_index("type")
    cel = [f"**{fr(d.loc[t].icc, 2)}** [{fr(d.loc[t].ci_bas, 2)} ; {fr(d.loc[t].ci_haut, 2)}]"
           for t in ("ICC(1,1)", "ICC(A,1)", "ICC(C,1)")]
    lignes.append(f"| {d['libelle'].iloc[0]} | {meth if col != 'dCT_region_um' else '(masques)'} | "
                  + " | ".join(cel) + " |")
display(Markdown("\n".join(lignes)))
chk = ICC_RAFT[ICC_RAFT["type"] == "ICC(1,1)"]
print("ecart max ICC(1,1) pingouin / manuel :", float((chk["icc"] - chk["icc11_manuel"]).abs().max()))

| marqueur | méthode | ICC(1,1) | ICC(A,1) | ICC(C,1) |
|:--|:--|--:|--:|--:|
| strain rétinien moyen | démons | **0,04** [-0,33 ; 0,75] | **0,10** [-0,24 ; 0,76] | **0,11** [-0,32 ; 0,79] |
| strain rétinien médian | démons | **0,28** [-0,20 ; 0,86] | **0,28** [-0,24 ; 0,86] | **0,27** [-0,24 ; 0,86] |
| strain rétinien p95 signé | démons | **-0,31** [-0,45 ; 0,33] | **-0,17** [-0,31 ; 0,44] | **-0,25** [-0,44 ; 0,46] |
| strain rétinien moyen | RAFT | **0,06** [-0,33 ; 0,76] | **0,09** [-0,27 ; 0,76] | **0,10** [-0,33 ; 0,78] |
| strain rétinien médian | RAFT | **0,05** [-0,33 ; 0,76] | **0,07** [-0,30 ; 0,76] | **0,08** [-0,33 ; 0,77] |
| strain rétinien p95 signé | RAFT | **-0,11** [-0,39 ; 0,64] | **-0,18** [-0,53 ; 0,64] | **-0,15** [-0,41 ; 0,60] |
| témoin : dCT de la bande (µm) | (masques) | **0,61** [0,08 ; 0,94] | **0,60** [-0,04 ; 0,94] | **0,54** [-0,03 ; 0,93] |

ecart max ICC(1,1) pingouin / manuel : 6.245004513516506e-17


## 5. Correspondance des pixels d'un réplicat à l'autre

Chaque réplicat a son propre crop et sa propre position dans l'image. La correspondance se fait en
quatre étapes :

1. chaque référence `fixed_global` (moyenne des bins minces) est replacée dans le repère plein de
   l'image (496 lignes), sur la fenêtre commune aux trois crops ;
2. OD2 et OD3 sont d'abord **translatés** sur OD1 par corrélation de phase (fenêtre de Hann, pic
   sous-pixel) ;
3. **RAFT** mesure ensuite le résidu non rigide entre les références ;
4. le déplacement total `v = u − d` envoie chaque pixel d'OD1 sur son analogue dans le réplicat.
   `warp_nan` reprend alors toute carte du réplicat dans le repère d'OD1.

Contrôle : NCC sur le tissu et Dice des rétines, avant et après.

In [9]:
H_PLEIN = 496
Y0 = min(PREPS[s].crop[0] for s in SLUGS)
Y1 = max(PREPS[s].crop[1] for s in SLUGS)


def plein(a, crop, fond=np.nan):
    out = np.full((H_PLEIN, a.shape[1]), fond, np.float32)
    out[crop[0]:crop[1]] = a
    return out[Y0:Y1]


def correlation_de_phase(a, b):
    # d = (dy, dx) tel que a(x) ~ b(x - d). Fenetre de Hann, pic parabolique sous-pixel.
    win = np.outer(np.hanning(a.shape[0]), np.hanning(a.shape[1]))
    A, B = np.fft.fft2((a - a.mean()) * win), np.fft.fft2((b - b.mean()) * win)
    R = A * np.conj(B)
    c = np.real(np.fft.ifft2(R / (np.abs(R) + 1e-9)))
    iy, ix = np.unravel_index(np.argmax(c), c.shape)
    d = []
    for ax, i in ((0, iy), (1, ix)):
        n = c.shape[ax]
        pic = (lambda j: c[j % n, ix]) if ax == 0 else (lambda j: c[iy, j % n])
        cm, c0, cp = pic(i - 1), pic(i), pic(i + 1)
        den = cm - 2 * c0 + cp
        off = 0.5 * (cm - cp) / den if den != 0 else 0.0
        d.append(((i + n // 2) % n - n // 2) + off)
    return np.array(d)


def ncc(a, b, m):
    a, b = a[m] - a[m].mean(), b[m] - b[m].mean()
    return float((a * b).sum() / np.sqrt((a * a).sum() * (b * b).sum()))


def dice(a, b):
    return float(2 * (a & b).sum() / (a.sum() + b.sum()))


REF = {}
for s in SLUGS:
    p = PREPS[s]
    img = plein(p.fixed_global, p.crop)
    img = np.where(np.isfinite(img), img, np.nanpercentile(img, 1))
    REF[s] = {"img": img, "retina": plein(p.retina, p.crop, 0) > 0.5,
              "roi": plein(p.roi, p.crop, 0) > 0.5, "tissue": plein(p.tissue, p.crop, 0) > 0.5}

S1 = SLUGS[0]
a = REF[S1]["img"]
V = {S1: np.zeros(a.shape + (2,))}
rows = []
for s in SLUGS[1:]:
    b = REF[s]["img"]
    d = correlation_de_phase(a, b)                       # (dy, dx)
    b_t = ndimage.shift(b, d, order=1, mode="nearest")  # b_t(x) = b(x - d)
    u = raft_flow(a, b_t, upscale=UPSCALE)
    v = u.copy()
    v[..., 0] -= d[1]
    v[..., 1] -= d[0]
    V[s] = v
    ret = warp(REF[s]["retina"].astype(np.float32), v) > 0.5
    ch = warp(REF[s]["roi"].astype(np.float32), v) > 0.5
    t = REF[S1]["tissue"]
    rows.append({"réplicat": s[-3:], "translation dy (px)": d[0], "translation dx (px)": d[1],
                 "|u| résiduel RAFT p95 (px)": float(np.percentile(np.hypot(u[..., 0], u[..., 1])[t], 95)),
                 "NCC avant": ncc(a, b, t), "NCC translation": ncc(a, b_t, t), "NCC après": ncc(a, warp(b, v), t),
                 "Dice rétine avant": dice(REF[S1]["retina"], REF[s]["retina"]),
                 "Dice rétine après": dice(REF[S1]["retina"], ret),
                 "Dice choroïde avant": dice(REF[S1]["roi"], REF[s]["roi"]),
                 "Dice choroïde après": dice(REF[S1]["roi"], ch)})
CORRESP = pd.DataFrame(rows)
display(CORRESP.round(3))
assert (CORRESP["Dice rétine après"] >= SEUIL_DICE).all(), "correspondance inter-replicats trop mauvaise"

,réplicat,translation dy (px),translation dx (px),|u| résiduel RAFT p95 (px),NCC avant,NCC translation,NCC après,Dice rétine avant,Dice rétine après,Dice choroïde avant,Dice choroïde après
0,OD2,50.814,2.182,7.344,0.079,0.828,0.897,0.399,0.970,0.183,0.979
1,OD3,32.958,-0.521,9.876,-0.047,0.748,0.891,0.582,0.983,0.424,0.969


## 6. Comparatif (2) : ICC pixel à pixel

On part des cartes de la paire marqueur de chaque réplicat.

- **Réduction** : pour chaque pixel, la **médiane sur les one-cycles**, reprise dans le repère d'OD1.
- **Sujets** : les pixels de la rétine d'OD1 (et, en contrôle, de la choroïde) valides dans les trois
  réplicats et classés dans le même tissu par la segmentation.
- **Calcul** : ICC(1,1), ICC(A,1) et ICC(C,1) par ANOVA vectorisée.

Les pixels voisins ne sont pas indépendants, car le champ est lisse pour RAFT comme pour les
démons, et l'IC analytique serait beaucoup trop étroit. Les IC95 viennent donc d'un **bootstrap par
blocs** (8 × 8 px, rééchantillonnés avec remise). On calcule aussi l'ICC sur les **moyennes de
blocs**, et le même calcul sur `u_y` : le déplacement, plus lisse que sa dérivée, sert de témoin.

Variante du comparatif (1) : un sujet par **A-scan** du repère commun, avec pour valeur la moyenne
de la carte sur la rétine de la colonne. Le bootstrap porte sur des paquets de 8 colonnes.

In [10]:
def icc3(mat):
    # (ICC(1,1), ICC(A,1), ICC(C,1)) pour une matrice sujets x evaluateurs.
    n, k = mat.shape
    g = mat.mean()
    rm, cm = mat.mean(1), mat.mean(0)
    ssr, ssc = k * ((rm - g) ** 2).sum(), n * ((cm - g) ** 2).sum()
    sst = ((mat - g) ** 2).sum()
    sse, ssw = sst - ssr - ssc, sst - ssr
    msr, msc = ssr / (n - 1), ssc / (k - 1)
    mse, msw = sse / ((n - 1) * (k - 1)), ssw / (n * (k - 1))
    return ((msr - msw) / (msr + (k - 1) * msw),
            (msr - mse) / (msr + (k - 1) * mse + k * (msc - mse) / n),
            (msr - mse) / (msr + (k - 1) * mse))


TYPES = ("ICC(1,1)", "ICC(A,1)", "ICC(C,1)")


def carte_mediane(f, cle, n_groups):
    cartes = [f[f"c{g}__{cle}"] for g in range(n_groups) if f"c{g}__{cle}" in f]
    return np.median(np.stack(cartes), axis=0)


def projeter(s, carte):
    # Carte croppee du replicat s -> repere commun d'OD1.
    return warp_nan(plein(carte, PREPS[s].crop), V[s])


PROJ = {}  # (methode, grandeur) -> (3, h, w) dans le repere d'OD1
for meth, src in (("RAFT", FIELDS), ("démons", DEMONS)):
    for cle in ("strain", "u_y"):
        PROJ[(meth, cle)] = np.stack([projeter(s, carte_mediane(src[s], cle, int(src[s]["n_groups"])))
                                      for s in SLUGS])

# Pixels analogues : meme tissu dans les trois replicats une fois projetes.
TISSUS = {}
for nom, cle in (("rétine", "retina"), ("choroïde", "roi")):
    m = REF[S1][cle].copy()
    for s in SLUGS[1:]:
        m &= warp(REF[s][cle].astype(np.float32), V[s]) > 0.5
    for arr in PROJ.values():
        m &= np.isfinite(arr).all(0)
    TISSUS[nom] = m
h, w = TISSUS["rétine"].shape
BLOC_ID = (np.arange(h)[:, None] // BLOC) * (w // BLOC + 1) + (np.arange(w)[None, :] // BLOC)


def icc_bootstrap(mat, groupes):
    # ICC ponctuel + IC95 par bootstrap des groupes (blocs de pixels ou paquets de colonnes).
    est = icc3(mat)
    uniq, inv = np.unique(groupes, return_inverse=True)
    ordre = np.argsort(inv, kind="stable")
    bornes = np.concatenate([[0], np.cumsum(np.bincount(inv))])
    membres = [ordre[bornes[i]:bornes[i + 1]] for i in range(uniq.size)]
    boot = np.empty((N_BOOT, 3))
    for i in range(N_BOOT):
        tirage = RNG.integers(0, uniq.size, uniq.size)
        boot[i] = icc3(mat[np.concatenate([membres[j] for j in tirage])])
    lo, hi = np.percentile(boot, [2.5, 97.5], axis=0)
    return est, lo, hi, uniq.size


rows = []
for (meth, cle), arr in PROJ.items():
    for tissu, m in TISSUS.items():
        mat = arr[:, m].T.astype(np.float64)       # pixels x replicats
        grp = BLOC_ID[m]
        est, lo, hi, n_grp = icc_bootstrap(mat, grp)
        # Moyennes de blocs : un sujet = un bloc rempli au moins a moitie.
        cnt = np.bincount(grp, minlength=BLOC_ID.max() + 1)
        garde = cnt >= BLOC * BLOC / 2
        blocs = np.stack([np.bincount(grp, weights=mat[:, j], minlength=cnt.size) for j in range(3)], 1)
        blocs = blocs[garde] / cnt[garde, None]
        est_b, lo_b, hi_b, _ = icc_bootstrap(blocs, np.arange(len(blocs)))
        r_paires = [np.corrcoef(mat[:, i], mat[:, j])[0, 1] for i, j in ((0, 1), (0, 2), (1, 2))]
        for t, e, l_, h_, eb, lb, hb in zip(TYPES, est, lo, hi, est_b, lo_b, hi_b):
            rows.append({"methode": meth, "grandeur": cle, "tissu": tissu, "type": t,
                         "icc_pixel": e, "ci_bas": l_, "ci_haut": h_, "n_pixels": len(mat),
                         "n_blocs": n_grp, "icc_blocs": eb, "ci_bas_blocs": lb, "ci_haut_blocs": hb,
                         "n_blocs_pleins": int(garde.sum()), "r_moyen_paires": float(np.mean(r_paires))})
    # Variante du comparatif (1) : un sujet = un A-scan, valeur = moyenne sur la retine de la colonne.
    m = TISSUS["rétine"]
    n_col = m.sum(0)
    ok = n_col >= 10
    prof = np.stack([np.where(m, arr[j], 0).sum(0)[ok] / n_col[ok] for j in range(3)], 1)
    est, lo, hi, n_grp = icc_bootstrap(prof, np.flatnonzero(ok) // BLOC)
    r_paires = [np.corrcoef(prof[:, i], prof[:, j])[0, 1] for i, j in ((0, 1), (0, 2), (1, 2))]
    for t, e, l_, h_ in zip(TYPES, est, lo, hi):
        rows.append({"methode": meth, "grandeur": cle, "tissu": "rétine, par A-scan", "type": t,
                     "icc_pixel": e, "ci_bas": l_, "ci_haut": h_, "n_pixels": int(ok.sum()),
                     "n_blocs": n_grp, "r_moyen_paires": float(np.mean(r_paires))})
ICC_PIXEL = pd.DataFrame(rows)

lignes = ["| grandeur | sujets (n) | méthode | ICC(1,1) [IC95 bootstrap] | ICC(A,1) | ICC(1,1) blocs 8×8 | r moyen des paires |",
          "|:--|:--|:--|--:|--:|--:|--:|"]
for (cle, tissu, meth), d in ICC_PIXEL.groupby(["grandeur", "tissu", "methode"], sort=False):
    d = d.set_index("type")
    a1, aa = d.loc["ICC(1,1)"], d.loc["ICC(A,1)"]
    blocs = (f"{fr(a1.icc_blocs, 2)} [{fr(a1.ci_bas_blocs, 2)} ; {fr(a1.ci_haut_blocs, 2)}]"
             if np.isfinite(a1.icc_blocs) else "—")
    lignes.append(f"| {'e_yy' if cle == 'strain' else 'u_y'} | {tissu} ({int(a1.n_pixels)}) | {meth} | "
                  f"**{fr(a1.icc_pixel, 2)}** [{fr(a1.ci_bas, 2)} ; {fr(a1.ci_haut, 2)}] | "
                  f"{fr(aa.icc_pixel, 2)} | {blocs} | {fr(a1.r_moyen_paires, 2)} |")
display(Markdown("\n".join(lignes)))

| grandeur | sujets (n) | méthode | ICC(1,1) [IC95 bootstrap] | ICC(A,1) | ICC(1,1) blocs 8×8 | r moyen des paires |
|:--|:--|:--|--:|--:|--:|--:|
| e_yy | rétine (59501) | RAFT | **0,10** [0,08 ; 0,14] | 0,10 | 0,21 [0,14 ; 0,29] | 0,11 |
| e_yy | choroïde (42092) | RAFT | **0,13** [0,11 ; 0,16] | 0,13 | 0,32 [0,26 ; 0,38] | 0,14 |
| e_yy | rétine, par A-scan (766) | RAFT | **0,19** [0,07 ; 0,31] | 0,20 | — | 0,20 |
| u_y | rétine (59501) | RAFT | **-0,21** [-0,22 ; -0,20] | -0,03 | -0,21 [-0,22 ; -0,19] | -0,00 |
| u_y | choroïde (42092) | RAFT | **-0,14** [-0,15 ; -0,12] | -0,04 | -0,14 [-0,15 ; -0,12] | 0,04 |
| u_y | rétine, par A-scan (766) | RAFT | **-0,17** [-0,22 ; -0,13] | -0,04 | — | 0,02 |
| e_yy | rétine (59501) | démons | **0,73** [0,71 ; 0,76] | 0,73 | 0,76 [0,73 ; 0,78] | 0,74 |
| e_yy | choroïde (42092) | démons | **0,74** [0,72 ; 0,77] | 0,75 | 0,76 [0,73 ; 0,78] | 0,81 |
| e_yy | rétine, par A-scan (766) | démons | **0,70** [0,55 ; 0,78] | 0,70 | — | 0,71 |
| u_y | rétine (59501) | démons | **0,15** [0,11 ; 0,18] | 0,20 | 0,13 [0,09 ; 0,17] | 0,36 |
| u_y | choroïde (42092) | démons | **0,41** [0,37 ; 0,46] | 0,44 | 0,42 [0,37 ; 0,46] | 0,56 |
| u_y | rétine, par A-scan (766) | démons | **0,07** [0,01 ; 0,12] | 0,12 | — | 0,26 |

### Témoin nul : bin mince → bin mince d'un autre one-cycle

Une carte de strain qui se répète pixel à pixel ne prouve pas qu'on mesure une déformation. Un
motif accroché à l'anatomie se répéterait tout autant, par exemple une réponse de la méthode aux
couches claires. On recale donc, avec chaque méthode, le bin mince du one-cycle g sur celui du
one-cycle g + 1 : deux choroïdes au minimum, où aucune dilatation n'est attendue. Les cartes nulles
passent ensuite par le même traitement : médiane, projection dans le repère d'OD1, ICC pixel sur la
rétine.

Si la carte nulle ressemble à la carte marqueur et se répète autant qu'elle, la répétabilité
pixel à pixel vient du motif et non de la pulsation. Dernière colonne : r entre la carte marqueur et
l'intensité de la référence, sur la rétine.

In [11]:
import SimpleITK as sitk  # noqa: E402
import os  # noqa: E402

sitk.ProcessObject.SetGlobalDefaultNumberOfThreads(os.cpu_count() or 8)
PARAMS_DEMONS = cds.DemonsParams(displacement_sigma=float(ocs.SIGMA))

NUL = {"RAFT": {}, "démons": {}}
t0 = time.perf_counter()
for s in SLUGS:
    p = PREPS[s]
    valides = [g for g in range(p.n_groups) if p.ref_bins[g] >= 0]
    cartes = {"RAFT": [], "démons": []}
    for g0, g1 in zip(valides[:-1], valides[1:]):
        fixe = p.cycles[g0 * N_BINS + int(p.ref_bins[g0])]
        mobile = p.cycles[g1 * N_BINS + int(p.ref_bins[g1])]
        cartes["RAFT"].append(cds.strain_yy(raft(fixe, mobile)["field"]))
        cartes["démons"].append(cds.strain_yy(cds.run_demons(cds.METHOD, fixe, mobile, PARAMS_DEMONS)["field"]))
    for meth in NUL:
        NUL[meth][s] = np.median(np.stack(cartes[meth]), axis=0)
print(f"temoin nul : {len(valides) - 1} paires par replicat, {time.perf_counter() - t0:.0f} s")

m = TISSUS["rétine"]
rows = []
for meth, src in (("démons", DEMONS), ("RAFT", FIELDS)):
    proj_nul = np.stack([projeter(s, NUL[meth][s]) for s in SLUGS])
    PROJ[(meth, "strain_nul")] = proj_nul
    ok = m & np.isfinite(proj_nul).all(0)
    icc_n = icc_bootstrap(proj_nul[:, ok].T.astype(np.float64), BLOC_ID[ok])
    icc_m = ICC_PIXEL[(ICC_PIXEL["methode"] == meth) & (ICC_PIXEL["grandeur"] == "strain")
                      & (ICC_PIXEL["tissu"] == "rétine") & (ICC_PIXEL["type"] == "ICC(1,1)")].iloc[0]
    for i, t in enumerate(TYPES):
        ICC_PIXEL.loc[len(ICC_PIXEL)] = {"methode": meth, "grandeur": "strain_nul", "tissu": "rétine", "type": t,
                                         "icc_pixel": icc_n[0][i], "ci_bas": icc_n[1][i], "ci_haut": icc_n[2][i],
                                         "n_pixels": int(ok.sum()), "n_blocs": icc_n[3]}
    for s in SLUGS:
        f = src[s]
        ret = f["retina"]
        marq = carte_mediane(f, "strain", int(f["n_groups"]))
        img = ndimage.gaussian_filter(PREPS[s].fixed_global.astype(np.float64), 1.5)
        rows.append({"méthode": meth, "réplicat": s[-3:],
                     "r(nul, marqueur)": np.corrcoef(NUL[meth][s][ret], marq[ret])[0, 1],
                     "σ nul / σ marqueur": NUL[meth][s][ret].std() / marq[ret].std(),
                     "moyenne nul ×1e3": 1e3 * NUL[meth][s][ret].mean(),
                     "moyenne marqueur ×1e3": 1e3 * marq[ret].mean(),
                     "ICC(1,1) pixel marqueur": icc_m.icc_pixel, "ICC(1,1) pixel nul": icc_n[0][0],
                     "r(marqueur, intensité)": np.corrcoef(marq[ret], img[ret])[0, 1]})
TEMOIN_NUL = pd.DataFrame(rows)
display(TEMOIN_NUL.round(3))

temoin nul : 4 paires par replicat, 87 s


,méthode,réplicat,"r(nul, marqueur)",σ nul / σ marqueur,moyenne nul ×1e3,moyenne marqueur ×1e3,"ICC(1,1) pixel marqueur","ICC(1,1) pixel nul","r(marqueur, intensité)"
0,démons,OD1,0.485,0.656,-0.891,0.249,0.735,0.434,0.465
1,démons,OD2,0.464,1.311,-2.886,0.648,0.735,0.434,0.536
2,démons,OD3,0.534,0.906,-2.820,0.322,0.735,0.434,0.379
3,RAFT,OD1,0.319,1.116,0.116,0.243,0.103,0.014,-0.148
4,RAFT,OD2,0.128,6.253,-0.616,0.179,0.103,0.014,-0.178
5,RAFT,OD3,0.366,0.902,0.004,0.204,0.103,0.014,-0.122


## 7. Figures

### Cartes de déplacement u_x et u_y (RAFT)

Paire bin mince → bin épais, rétine et choroïde. Une ligne par one-cycle, une colonne par réplicat.
L'échelle est commune et bornée au p99 ; les pointillés marquent les bandes latérales.

In [12]:
N_CYC = max(int(FIELDS[s]["n_groups"]) for s in SLUGS)
BINS_EPAIS = BINS[BINS["is_thick"]]


def carte(src, cle, echelle, titre, unite, fmt, cmap="RdBu_r"):
    titres = []
    for g in range(N_CYC):
        for s in SLUGS:
            b = BINS_EPAIS[(BINS_EPAIS["slug"] == s) & (BINS_EPAIS["one_cycle"] == g + 1)]
            titres.append(f"{s[-3:]} · cycle {g + 1} : absent" if b.empty else
                          f"{s[-3:]} · cycle {g + 1} · bins {int(b.iloc[0].ref_bin)}→{int(b.iloc[0].bin)}"
                          f" · ΔCT {fr(b.iloc[0].dCT_um)} µm")
    fig = make_subplots(rows=N_CYC, cols=len(SLUGS), subplot_titles=titres, shared_xaxes=True,
                        shared_yaxes=True, horizontal_spacing=0.02, vertical_spacing=0.035)
    fac = lambda f: float(f[echelle]) if echelle else 1.0  # noqa: E731
    valeurs = [np.abs(f[f"c{g}__{cle}"] * fac(f))[f["tissue"]]
               for f in (src[s] for s in SLUGS) for g in range(int(f["n_groups"])) if f"c{g}__{cle}" in f]
    lim = float(np.percentile(np.concatenate(valeurs), 99))
    for j, s in enumerate(SLUGS):
        f = src[s]
        um_y, um_x = float(f["um_y"]), float(f["um_x"])
        hh, ww = f["tissue"].shape
        y, x = np.arange(0, hh, DS_Y) * um_y, np.arange(0, ww, DS_X) * um_x
        bords = [int(np.flatnonzero(m.any(axis=0))[0]) for m in f["column_masks"][1:]]
        for g in range(N_CYC):
            if f"c{g}__{cle}" not in f:
                continue
            z = np.where(f["tissue"], f[f"c{g}__{cle}"] * fac(f), np.nan)[::DS_Y, ::DS_X].astype(np.float32)
            fig.add_trace(go.Heatmap(x=x, y=y, z=z, coloraxis="coloraxis",
                                     hovertemplate=(f"{s} · cycle {g + 1}<br>%{{x:.0f}} µm, %{{y:.0f}} µm"
                                                    f"<br>{unite} %{{z:{fmt}}}<extra></extra>")),
                          row=g + 1, col=j + 1)
            for xb in bords:
                fig.add_vline(x=xb * um_x, row=g + 1, col=j + 1, line={"color": "gray", "width": 1, "dash": "dot"})
    fig.update_yaxes(autorange="reversed")
    fig.update_layout(height=210 * N_CYC + 120, title=titre,
                      coloraxis={"colorscale": cmap, "cmin": -lim, "cmax": lim, "cmid": 0,
                                 "colorbar": {"title": {"text": unite}, "len": 0.5}})
    fig.show()


carte(FIELDS, "u_x", "um_x", "RAFT — déplacement latéral u_x (µm), bin mince → bin épais", "u_x (µm)", ".2f", "PuOr")

In [13]:
carte(FIELDS, "u_y", "um_y", "RAFT — déplacement axial u_y (µm), bin mince → bin épais", "u_y (µm)", ".2f")

### Cartes de strain axial e_yy = ∂u_y/∂y (RAFT)

In [14]:
carte(FIELDS, "strain", None, "RAFT — strain axial e_yy, bin mince → bin épais", "e_yy", ".4f")

### RAFT contre démons, même paire

Cycle 1 de chaque réplicat. Lignes, de haut en bas : u_y démons, u_y RAFT, e_yy démons, e_yy RAFT.
Chaque grandeur a sa propre échelle, commune aux deux méthodes.

In [15]:
G = 0
lignes_fig = [("démons", "u_y", DEMONS), ("RAFT", "u_y", FIELDS), ("démons", "strain", DEMONS), ("RAFT", "strain", FIELDS)]
fig = make_subplots(rows=4, cols=len(SLUGS), shared_xaxes=True, shared_yaxes=True,
                    horizontal_spacing=0.02, vertical_spacing=0.05,
                    subplot_titles=[f"{s[-3:]} · {meth} · {'u_y (µm)' if cle == 'u_y' else 'e_yy'}"
                                    for meth, cle, _ in lignes_fig for s in SLUGS])
lims = {}
for cle in ("u_y", "strain"):
    v = [np.abs(src[s][f"c{G}__{cle}"] * (float(src[s]["um_y"]) if cle == "u_y" else 1))[src[s]["tissue"]]
         for _, c_, src in lignes_fig if c_ == cle for s in SLUGS]
    lims[cle] = float(np.percentile(np.concatenate(v), 99))
for i, (meth, cle, src) in enumerate(lignes_fig, start=1):
    for j, s in enumerate(SLUGS, start=1):
        f = src[s]
        um_y, um_x = float(f["um_y"]), float(f["um_x"])
        hh, ww = f["tissue"].shape
        z = np.where(f["tissue"], f[f"c{G}__{cle}"] * (um_y if cle == "u_y" else 1), np.nan)[::DS_Y, ::DS_X]
        fig.add_trace(go.Heatmap(x=np.arange(0, ww, DS_X) * um_x, y=np.arange(0, hh, DS_Y) * um_y,
                                 z=z.astype(np.float32), coloraxis="coloraxis" if cle == "u_y" else "coloraxis2",
                                 hovertemplate=f"{s} · {meth}<br>%{{x:.0f}} µm, %{{y:.0f}} µm<br>%{{z:.4f}}<extra></extra>"),
                      row=i, col=j)
fig.update_yaxes(autorange="reversed")
fig.update_layout(height=900, title=f"Cycle {G + 1} : démons (σ = 15) contre RAFT, bin mince → bin épais",
                  coloraxis={"colorscale": "RdBu_r", "cmin": -lims["u_y"], "cmax": lims["u_y"],
                             "colorbar": {"title": {"text": "u_y (µm)"}, "len": 0.45, "y": 0.77}},
                  coloraxis2={"colorscale": "RdBu_r", "cmin": -lims["strain"], "cmax": lims["strain"],
                              "colorbar": {"title": {"text": "e_yy"}, "len": 0.45, "y": 0.23}})
fig.show()

### Cartes médianes dans le repère d'OD1

Pour chaque réplicat, la médiane des one-cycles, reprise dans le repère d'OD1. La dernière colonne
donne l'écart-type entre réplicats, pixel par pixel. Seuls les pixels analogues sont affichés
(rétine ∪ choroïde). Les deux lignes du bas montrent le témoin nul (bin mince → bin mince), à la
même échelle.

In [16]:
masque = TISSUS["rétine"] | TISSUS["choroïde"]
um_y, um_x = PREPS[S1].um_y, PREPS[S1].um_x
LIGNES_MED = [("démons", "strain", "marqueur"), ("RAFT", "strain", "marqueur"),
              ("démons", "strain_nul", "témoin nul"), ("RAFT", "strain_nul", "témoin nul")]
fig = make_subplots(rows=4, cols=4, shared_xaxes=True, shared_yaxes=True, horizontal_spacing=0.02,
                    vertical_spacing=0.06,
                    subplot_titles=[t for meth, _, lib in LIGNES_MED for t in
                                    [f"{meth} · {lib} · {s[-3:]}{' → OD1' if s != S1 else ''}" for s in SLUGS]
                                    + [f"{meth} · {lib} · écart-type"]])
lim = float(np.nanpercentile(np.abs(np.concatenate([PROJ[(m_, c_)][:, masque].ravel()
                                                    for m_, c_, _ in LIGNES_MED])), 99))
lim_sd = float(np.nanpercentile(np.concatenate([PROJ[(m_, c_)][:, masque].std(0)
                                                for m_, c_, _ in LIGNES_MED]), 99))
y = (Y0 + np.arange(0, h, DS_Y)) * um_y
x = np.arange(0, w, DS_X) * um_x
for i, (meth, cle, lib) in enumerate(LIGNES_MED, start=1):
    arr = PROJ[(meth, cle)]
    for j in range(len(SLUGS)):
        z = np.where(masque, arr[j], np.nan)[::DS_Y, ::DS_X].astype(np.float32)
        fig.add_trace(go.Heatmap(x=x, y=y, z=z, coloraxis="coloraxis",
                                 hovertemplate=f"{meth} · {SLUGS[j][-3:]}<br>e_yy %{{z:.4f}}<extra></extra>"),
                      row=i, col=j + 1)
    z = np.where(masque, arr.std(0), np.nan)[::DS_Y, ::DS_X].astype(np.float32)
    fig.add_trace(go.Heatmap(x=x, y=y, z=z, coloraxis="coloraxis2",
                             hovertemplate=f"{meth} · écart-type<br>%{{z:.4f}}<extra></extra>"), row=i, col=4)
fig.update_yaxes(autorange="reversed")
fig.update_layout(height=1150, title="Strain e_yy médian par réplicat, repère commun d'OD1 (marqueur et témoin nul)",
                  coloraxis={"colorscale": "RdBu_r", "cmin": -lim, "cmax": lim,
                             "colorbar": {"title": {"text": "e_yy"}, "len": 0.45, "y": 0.8}},
                  coloraxis2={"colorscale": "Viridis", "cmin": 0, "cmax": lim_sd,
                              "colorbar": {"title": {"text": "σ inter"}, "len": 0.45, "y": 0.2}})
fig.show()

### Pixel contre pixel, rétine

Histogramme 2D du strain médian de deux réplicats, aux mêmes pixels d'OD1. Une colonne par paire de
réplicats, une ligne par méthode, et le r de Pearson dans le titre de chaque panneau.

In [17]:
m = TISSUS["rétine"]
paires = ((0, 1), (0, 2), (1, 2))
titres = []
for meth in ("démons", "RAFT"):
    arr = PROJ[(meth, "strain")][:, m]
    for i, j in paires:
        titres.append(f"{meth} · {SLUGS[i][-3:]} / {SLUGS[j][-3:]} · r = {fr(np.corrcoef(arr[i], arr[j])[0, 1], 2)}")
fig = make_subplots(rows=2, cols=3, subplot_titles=titres, horizontal_spacing=0.07, vertical_spacing=0.12)
for r_, meth in enumerate(("démons", "RAFT"), start=1):
    arr = PROJ[(meth, "strain")][:, m]
    lim = float(np.percentile(np.abs(arr), 99.5))
    for c_, (i, j) in enumerate(paires, start=1):
        fig.add_trace(go.Histogram2d(x=arr[i], y=arr[j], coloraxis="coloraxis",
                                     xbins={"start": -lim, "end": lim, "size": 2 * lim / 80},
                                     ybins={"start": -lim, "end": lim, "size": 2 * lim / 80}),
                      row=r_, col=c_)
        fig.add_trace(go.Scatter(x=[-lim, lim], y=[-lim, lim], mode="lines", showlegend=False,
                                 line={"color": "gray", "dash": "dot", "width": 1}, hoverinfo="skip"),
                      row=r_, col=c_)
        fig.update_xaxes(title_text=f"e_yy {SLUGS[i][-3:]}", row=r_, col=c_)
        fig.update_yaxes(title_text=f"e_yy {SLUGS[j][-3:]}", row=r_, col=c_)
fig.update_layout(height=760, title=f"Strain rétinien médian, pixel à pixel ({int(m.sum())} pixels analogues)",
                  coloraxis={"colorscale": "Blues", "colorbar": {"title": {"text": "pixels"}}})
fig.show()

### Profil latéral : strain rétinien moyen par A-scan

Pour chaque A-scan du repère d'OD1, la moyenne du strain médian sur la rétine. Une courbe par
réplicat ; démons en haut, RAFT en bas.

In [18]:
m = TISSUS["rétine"]
n_col = m.sum(0)
ok = n_col >= 10


def icc_ascan(meth):
    d = ICC_PIXEL[(ICC_PIXEL["methode"] == meth) & (ICC_PIXEL["grandeur"] == "strain")
                  & (ICC_PIXEL["tissu"] == "rétine, par A-scan") & (ICC_PIXEL["type"] == "ICC(1,1)")]
    return float(d["icc_pixel"].iloc[0])


fig = make_subplots(rows=2, cols=1, shared_xaxes=True, vertical_spacing=0.08,
                    subplot_titles=[f"{meth} · ICC(1,1) par A-scan = {fr(icc_ascan(meth), 2)}"
                                    for meth in ("démons", "RAFT")])
for r_, meth in enumerate(("démons", "RAFT"), start=1):
    arr = PROJ[(meth, "strain")]
    for j, s in enumerate(SLUGS):
        prof = np.where(ok, np.where(m, arr[j], 0).sum(0) / np.maximum(n_col, 1), np.nan)
        rep = int(s[-1])
        fig.add_trace(go.Scatter(x=np.arange(w) * um_x, y=prof * 1e3, mode="lines", name=f"réplicat {rep}",
                                 legendgroup=str(rep), showlegend=r_ == 1,
                                 line={"color": C_REPLICAT[rep], "width": 1.5}), row=r_, col=1)
    fig.add_hline(y=0, line={"color": "gray", "width": 1}, row=r_, col=1)
    fig.update_yaxes(title_text="e_yy rétinien (× 10⁻³)", row=r_, col=1)
fig.update_xaxes(title_text="position latérale dans le repère d'OD1 (µm)", row=2, col=1)
fig.update_layout(height=620, title="Profil latéral du strain rétinien médian")
fig.show()

### Strain rétinien moyen par bande (RAFT)

Un box par réplicat, un point par one-cycle.

In [19]:
BANDES = [cds.column_label(k, "OD") for k in range(N_COLUMNS)]
fig = go.Figure()
for s in SLUGS:
    rep = int(s[-1])
    d = MARK[MARK["slug"] == s].sort_values(["k", "one_cycle"])
    fig.add_trace(go.Box(
        x=d["region"], y=d["strain_retine"] * 1e3, name=f"réplicat {rep} ({s[-3:]})",
        offsetgroup=str(rep), marker={"color": C_REPLICAT[rep], "size": 8},
        line={"color": C_REPLICAT[rep], "width": 2}, fillcolor="rgba(0,0,0,0)",
        boxpoints="all", jitter=0.35, pointpos=0, customdata=d["one_cycle"],
        hovertemplate=f"réplicat {rep} · %{{x}}<br>cycle %{{customdata}} : %{{y:.3f}} × 10⁻³<extra></extra>"))
fig.add_hline(y=0, line={"color": "gray", "width": 1})
fig.update_xaxes(categoryorder="array", categoryarray=BANDES, title_text="bande latérale")
fig.update_yaxes(title_text="strain rétinien moyen (× 10⁻³)")
fig.update_layout(boxmode="group", height=500, title="RAFT — strain rétinien moyen par bande, bin mince → bin épais")
fig.show()

### Synthèse des ICC(1,1)

Le point donne l'estimation, la barre l'IC95 : analytique pour les bandes, par bootstrap de blocs
pour les pixels et les A-scans.

In [20]:
lignes = []
for meth in ("démons", "RAFT"):
    d = ICC_BANDES[(ICC_BANDES["methode"] == meth) & (ICC_BANDES["marqueur"] == "strain_retine")
                   & (ICC_BANDES["type"] == "ICC(1,1)")].iloc[0]
    lignes.append((meth, "bandes (5)", d.icc, d.ci_bas, d.ci_haut))
    for tissu, lib in (("rétine, par A-scan", "A-scans"), ("rétine", "pixels rétine"), ("choroïde", "pixels choroïde")):
        d = ICC_PIXEL[(ICC_PIXEL["methode"] == meth) & (ICC_PIXEL["grandeur"] == "strain")
                      & (ICC_PIXEL["tissu"] == tissu) & (ICC_PIXEL["type"] == "ICC(1,1)")].iloc[0]
        lignes.append((meth, lib, d.icc_pixel, d.ci_bas, d.ci_haut))
    d = ICC_PIXEL[(ICC_PIXEL["methode"] == meth) & (ICC_PIXEL["grandeur"] == "strain_nul")
                  & (ICC_PIXEL["type"] == "ICC(1,1)")].iloc[0]
    lignes.append((meth, "pixels rétine, témoin nul", d.icc_pixel, d.ci_bas, d.ci_haut))
SYNTHESE = pd.DataFrame(lignes, columns=["methode", "niveau", "icc", "lo", "hi"])
dct = ICC_BANDES[(ICC_BANDES["methode"] == "RAFT") & (ICC_BANDES["marqueur"] == "dCT_region_um")
                 & (ICC_BANDES["type"] == "ICC(1,1)")].iloc[0]
fig = go.Figure()
for meth in ("démons", "RAFT"):
    d = SYNTHESE[SYNTHESE["methode"] == meth]
    fig.add_trace(go.Scatter(x=d["niveau"], y=d["icc"], mode="markers", name=meth, offsetgroup=meth,
                             marker={"color": C_METHODE[meth], "size": 11},
                             error_y={"type": "data", "symmetric": False, "array": d["hi"] - d["icc"],
                                      "arrayminus": d["icc"] - d["lo"]},
                             hovertemplate=f"{meth} · %{{x}}<br>ICC(1,1) %{{y:.2f}}<extra></extra>"))
fig.add_hline(y=dct.icc, line={"color": "#1baf7a", "dash": "dash"},
              annotation_text=f"témoin dCT par bande : {fr(dct.icc, 2)}", annotation_position="top left")
fig.add_hline(y=0, line={"color": "gray", "width": 1})
fig.update_layout(scattermode="group", height=450, yaxis={"title": "ICC(1,1) du strain e_yy", "range": [-0.6, 1]},
                  title="Répétabilité du strain entre réplicats : démons contre RAFT")
fig.show()

## 8. Sauvegarde

Écrit sous `one_cycle_6beats_6bins/raft_strain/` :
- les tables `bins`, `regions`, `markers`, `icc` (bandes), `icc_pixel`, `controle`, `correspondance`,
  `synthetique` et `temoin_nul` ;
- les champs de la paire marqueur, dans `fields/<slug>.npz` (même format que les démons, avec `u_x`
  en plus) ;
- les cartes projetées et les déplacements inter-réplicats, dans `projected.npz`.

In [21]:
(OUT_DIR / "fields").mkdir(parents=True, exist_ok=True)
BINS.to_csv(OUT_DIR / "bins.csv", index=False)
REGIONS.to_csv(OUT_DIR / "regions.csv", index=False)
MARK.to_csv(OUT_DIR / "markers.csv", index=False)
ICC_RAFT.to_csv(OUT_DIR / "icc.csv", index=False)
ICC_PIXEL.to_csv(OUT_DIR / "icc_pixel.csv", index=False)
CONTROLE.to_csv(OUT_DIR / "controle.csv", index=False)
CORRESP.to_csv(OUT_DIR / "correspondance.csv", index=False)
SYNTH.to_csv(OUT_DIR / "synthetique.csv", index=False)
TEMOIN_NUL.to_csv(OUT_DIR / "temoin_nul.csv", index=False)
for s in SLUGS:
    np.savez_compressed(OUT_DIR / "fields" / f"{s}.npz", **FIELDS[s])
np.savez_compressed(
    OUT_DIR / "projected.npz", y0=Y0, y1=Y1, retine=TISSUS["rétine"], choroide=TISSUS["choroïde"],
    **{f"{'raft' if m_ == 'RAFT' else 'demons'}__{c_}": a_.astype(np.float32) for (m_, c_), a_ in PROJ.items()},
    **{f"v__{s}": V[s].astype(np.float32) for s in SLUGS})
params = {"slugs": list(SLUGS), "methode": "RAFT large (torchvision), poids C_T_SKHT_V2",
          "upscale": UPSCALE, "iters": RAFT_ITERS, "strain": "cds.strain_yy, sans lissage",
          "marker_pair": "bin de CT minimum -> bin de CT maximum, par one-cycle",
          "icc_bandes": "targets = region (5 bandes), raters = replicat, valeur = mediane des one-cycles",
          "icc_pixel": "cartes medianes des one-cycles reprises dans le repere d'OD1 (correlation de phase + RAFT "
                       "entre fixed_global), sujets = pixels analogues, IC par bootstrap de blocs",
          "bloc_px": BLOC, "n_boot": N_BOOT, "one_cycles": str(ONE_CYCLE_DIR), "demons": str(DEMONS_DIR),
          "created": datetime.now().isoformat(timespec="seconds")}
(OUT_DIR / "params.json").write_text(json.dumps(params, indent=2, ensure_ascii=False), encoding="utf-8")
print(f"-> {OUT_DIR}")

-> E:\NASA_Rigidity\Reproducibility\SegmentationVariations\cascade_v9_1536x1024_hr_mediane\one_cycle_6beats_6bins\raft_strain
